<a href="https://colab.research.google.com/github/juliamota1/CN-unifesp/blob/main/Animacao_Eliminacao_Gauss.ipynb" target="_parent"><img src="https://colab.research.google.com/assets/colab-badge.svg" alt="Open In Colab"/></a>

# Animação da Eliminação de Gauss



**Ideia de implementação (3 etapas):**
1. **Gerar os quadros-chave:** repetimos o algoritmo de Gauss do notebook original, mas, em vez de só calcular, *gravamos* a matriz aumentada, o pivô, as linhas envolvidas e a operação $R_i\leftarrow R_i-m_{ik}R_k$ em cada passo.
2. **Desenhar um quadro:** uma função recebe um quadro e desenha a matriz com `matplotlib` (pivô em azul, linha-alvo em laranja, zeros criados em verde).
3. **Animar:** `FuncAnimation` percorre os quadros. Entre o "antes" e o "depois" de cada operação, interpolamos linearmente os valores da linha para que os números *escorram* até o novo valor.

Com `pivoteamento=True`, as trocas de linha também são animadas (as linhas deslizam para trocar de lugar).

In [1]:
%matplotlib inline
import numpy as np
import matplotlib
import matplotlib.pyplot as plt
from matplotlib.animation import FuncAnimation, PillowWriter
from matplotlib.patches import Rectangle
from fractions import Fraction

# ---------- 1) formatação: mostra frações quando possível (como no notebook) ----------
def fmt(v, dec=False):
    if abs(v) < 1e-12:
        return "0"
    if dec:
        return f"{v:.2f}"
    f = Fraction(float(v)).limit_denominator(1000)
    if abs(float(f) - v) < 1e-9:
        return str(f.numerator) if f.denominator == 1 else f"{f.numerator}/{f.denominator}"
    return f"{v:.2f}"

# ---------- 2) gera os "quadros-chave" do algoritmo (sem desenhar nada ainda) ----------
def gerar_quadros(A, b, pivoteamento=True, n_interp=10):
    """Executa Gauss e grava cada passo. Cada quadro é um dict com a matriz e os destaques."""
    M = np.column_stack([A, b]).astype(float)
    n = len(b)
    Q = []

    def add(M, titulo, op="", pivo=None, linhas=(), zeros=(), pos=None, rep=1, sol=None, lin_sol=None, dec=False):
        Q.append(dict(M=M.copy(), titulo=titulo, op=op, pivo=pivo, linhas=linhas, zeros=zeros,
                      pos=np.arange(n, dtype=float) if pos is None else np.array(pos, float),
                      rep=rep, sol=dict(sol or {}), lin_sol=lin_sol, dec=dec))

    add(M, "Matriz aumentada [A | b]", rep=8)

    for k in range(n - 1):
        # --- pivoteamento parcial ---
        if pivoteamento:
            p = k + int(np.argmax(np.abs(M[k:, k])))
            if p != k:
                add(M, f"Coluna {k+1}: maior pivô está na linha {p+1}",
                    rf"$R_{k+1}\leftrightarrow R_{p+1}$", pivo=(p, k), linhas=(k, p), rep=6)
                for t in np.linspace(0, 1, n_interp)[1:]:       # linhas "deslizam" até trocar
                    pos = np.arange(n, dtype=float)
                    pos[k] = k + t * (p - k); pos[p] = p + t * (k - p)
                    add(M, f"Trocando linhas {k+1} e {p+1}", rf"$R_{k+1}\leftrightarrow R_{p+1}$",
                        linhas=(k, p), pos=pos, dec=True)
                M[[k, p]] = M[[p, k]]
        if abs(M[k, k]) < 1e-12:
            raise np.linalg.LinAlgError("Pivô nulo")

        for i in range(k + 1, n):
            m = M[i, k] / M[k, k]
            op = rf"$R_{i+1}\leftarrow R_{i+1} - ({fmt(m)})\,R_{k+1}$"
            tit = f"Pivô = {fmt(M[k,k])}   |   m{i+1}{k+1} = ({fmt(M[i,k])}) / ({fmt(M[k,k])}) = {fmt(m)}"
            add(M, tit, op, pivo=(k, k), linhas=(k, i), rep=8)
            antes, depois = M[i].copy(), M[i] - m * M[k]
            depois[k] = 0.0
            for t in np.linspace(0, 1, n_interp)[1:]:           # números "escorrem" até o novo valor
                M2 = M.copy(); M2[i] = (1 - t) * antes + t * depois
                add(M2, tit, op, pivo=(k, k), linhas=(k, i), zeros=((i, k),) if t == 1 else (), dec=(t < 1))
            M[i] = depois
            add(M, f"Zeramos a posição ({i+1},{k+1})", op, pivo=(k, k), linhas=(k, i),
                zeros=((i, k),), rep=6)

    add(M, "Forma triangular superior  [U | c]", rep=10)

    # --- substituição regressiva ---
    U, c = M[:, :n], M[:, n]
    x = np.zeros(n); sol = {}
    for i in range(n - 1, -1, -1):
        x[i] = (c[i] - U[i, i+1:] @ x[i+1:]) / U[i, i]
        sol[i] = x[i]
        add(M, "Substituição regressiva", None, pivo=(i, i), linhas=(i,), rep=12, sol=sol, lin_sol=i)
    add(M, "Solução", None, rep=16, sol=sol)
    return Q, x

# ---------- 3) desenho de um quadro ----------
def desenhar(ax, q, nomes):
    ax.clear(); ax.set_axis_off()
    M = q["M"]; n = len(M); w, h = 1.25, 0.9
    ax.set_xlim(-1.2, (n + 1) * w + 4.2); ax.set_ylim(-(n + 0.3) * h, 1.7 * h)

    def xy(r, c):                       # centro da célula (r,c); coluna n = termo independente
        return c * w + (0.45 if c == n else 0), -q["pos"][r] * h

    # destaques de linhas
    for r in q["linhas"]:
        cor = "#CFE8FF" if (q["pivo"] and r == q["pivo"][0]) else "#FFE2B8"
        if q["lin_sol"] is not None: cor = "#D6F5D6"
        x0, y0 = xy(r, 0)
        ax.add_patch(Rectangle((x0 - w/2, y0 - h/2), (n + 1) * w + 0.45, h, color=cor, zorder=0))
    # pivô
    if q["pivo"]:
        x0, y0 = xy(*q["pivo"])
        ax.add_patch(Rectangle((x0 - w/2 + .05, y0 - h/2 + .05), w - .1, h - .1, fill=False, ec="#1565C0", lw=2.5))
    # zeros recém-criados
    for (r, c) in q["zeros"]:
        x0, y0 = xy(r, c)
        ax.add_patch(Rectangle((x0 - w/2 + .05, y0 - h/2 + .05), w - .1, h - .1, fill=False, ec="#2E7D32", lw=2.5))

    # números
    for r in range(n):
        for c in range(n + 1):
            x0, y0 = xy(r, c)
            ax.text(x0, y0, fmt(M[r, c], q["dec"]), ha="center", va="center", fontsize=15, zorder=3, family="DejaVu Sans")
        x0, y0 = xy(r, 0)
        ax.text(x0 - w/2 - .15, y0, rf"$R_{r+1}$" if abs(q['pos'][r]-r) < 1e-9 else "", ha="right", va="center", fontsize=11, color="gray")

    # colchetes e barra de [A | b]
    top, bot = h/2, -(n - 1) * h - h/2
    xl, xr = -w/2 - .05, n * w + .45 + w/2 + .05
    for xx, d in ((xl, 1), (xr, -1)):
        ax.plot([xx + d*.12, xx, xx, xx + d*.12], [top, top, bot, bot], "k", lw=1.8)
    xb = (n - .5) * w + .22
    ax.plot([xb, xb], [top, bot], "k", lw=1.2, ls="--")
    for c in range(n):
        ax.text(c * w, top + .15*h, nomes[c], ha="center", va="bottom", fontsize=11, color="gray")

    # textos
    ax.text((n * w) / 2, 1.05 * h, q["titulo"], ha="center", va="bottom", fontsize=13, weight="bold")
    if q["op"]:
        ax.text((n * w) / 2, bot - .55*h, q["op"], ha="center", va="center", fontsize=16, color="#BF360C")

    # painel da solução (lado direito)
    if q["sol"]:
        xs = (n + 1) * w + 1.0
        ax.text(xs, top, "Solução:", fontsize=13, weight="bold", va="center")
        for j, i in enumerate(sorted(q["sol"], reverse=True)):
            dest = (i == q["lin_sol"])
            ax.text(xs, top - (j + 1) * h * .85, f"{nomes[i]} = {fmt(q['sol'][i])}", fontsize=15, va="center",
                    color="#2E7D32" if dest else "black", weight="bold" if dest else "normal")

# ---------- 4) monta a animação ----------
def animar_gauss(A, b, pivoteamento=True, nomes=None, intervalo=90):
    A = np.asarray(A, float); n = len(b)
    nomes = nomes or [f"x{i+1}" for i in range(n)]
    Q, x = gerar_quadros(A, b, pivoteamento)
    quadros = [q for q in Q for _ in range(q["rep"])]          # 'rep' = quantos frames o quadro fica parado
    fig, ax = plt.subplots(figsize=(9, 2.6 + .55 * n))
    anim = FuncAnimation(fig, lambda f: desenhar(ax, quadros[f], nomes),
                         frames=len(quadros), interval=intervalo, repeat=True)
    plt.close(fig)
    return anim, x


## Exemplo da seção 3 (sem pivoteamento)

$2x+y-z=8,\; -3x-y+2z=-11,\; -2x+y+2z=-3$. A solução esperada é $(2,3,-1)$.

In [2]:
A_g = [[2,1,-1],[-3,-1,2],[-2,1,2]]
b_g = [8,-11,-3]

anim, x = animar_gauss(A_g, b_g, pivoteamento=False, nomes=["x","y","z"])
print("Solução:", x)

from IPython.display import HTML
HTML(anim.to_jshtml())   # player com play/pause e controle de velocidade

Solução: [ 2.  3. -1.]


## Exemplo da seção 4: pivô nulo exige troca de linhas

In [3]:
anim2, x2 = animar_gauss([[0,2],[1,1]], [4,3], pivoteamento=True, nomes=["x","y"])
print("Solução:", x2)
HTML(anim2.to_jshtml())

Solução: [1. 2.]


## Exemplo da seção 1: rede térmica (com pivoteamento)

In [4]:
A = [[4,-1,0],[-1,4,-1],[0,-1,3]]
b = [100,100,50]
anim3, x3 = animar_gauss(A, b, pivoteamento=True, nomes=["T1","T2","T3"])
print("Solução:", x3)
HTML(anim3.to_jshtml())

Solução: [35.36585366 41.46341463 30.48780488]


## Salvar como GIF


In [5]:
anim.save("gauss_animacao.gif", writer=PillowWriter(fps=11))
print("GIF salvo: gauss_animacao.gif")

GIF salvo: gauss_animacao.gif


### Para personalizar
- **Velocidade:** `intervalo=` em `animar_gauss` (ms por frame) ou `fps=` ao salvar.
- **Tempo parado em cada passo:** o campo `rep` em `add(...)` (quantos frames o quadro permanece).
- **Suavidade da transição:** `n_interp` em `gerar_quadros`.
- **Matrizes maiores:** funciona para qualquer $n$, mas acima de $n=5$ os números começam a ficar pequenos; aumente o `figsize`.
- **Extensão natural:** adaptar `gerar_quadros` para a fatoração LU, guardando os multiplicadores $m_{ik}$ em $L$ ao lado de $U$.